# Learned Stage-Wise Curvature Tuning on Arabic Digits

This notebook evaluates Learned Stage-Wise Curvature Tuning (SW-CT) on the Arabic Handwritten Digits dataset using an ImageNet-pretrained ResNet-18.

Arabic Digits is substantially different from natural-image datasets such as Beans, DTD, Flowers102, and FGVC-Aircraft. The images contain handwritten numerical symbols rather than natural objects or textures. This provides a stronger domain-shift experiment for evaluating whether Learned SW-CT can adapt the curvature of a pretrained network to a visually different downstream task.

The experiments compare four conditions:

1. **Baseline** — the original pretrained ResNet with ReLU activations and a trained downstream classifier.
2. **Single-Parameter Curvature Tuning (S-CT)** — one global beta selected through validation-based exhaustive search.
3. **Learned SW-CT with fixed initialization** — four trainable stage-wise beta parameters initialized at 0.78.
4. **Learned SW-CT with random initialization** — four trainable stage-wise beta parameters independently initialized between 0.70 and 0.99.

Each condition is evaluated using seeds 42, 43, and 44.

Experiments are conducted for both 20 and 30 epochs to determine whether additional optimization improves performance or changes the learned stage-wise beta values.

Wall-clock execution time is also recorded to compare the computational cost of Baseline, S-CT, and Learned SW-CT.

In [1]:
!nvidia-smi

Thu Oct  1 19:53:34 2026       
+-----------------------------------------------------------------------------------------+
| NVIDIA-SMI 580.178.04             Driver Version: 580.178.04     CUDA Version: 13.0     |
+-----------------------------------------+------------------------+----------------------+
| GPU  Name                 Persistence-M | Bus-Id          Disp.A | Volatile Uncorr. ECC |
| Fan  Temp   Perf          Pwr:Usage/Cap |           Memory-Usage | GPU-Util  Compute M. |
|                                         |                        |               MIG M. |
|=========================================+========================+======================|
|   0  Tesla T4                       Off |   00000000:00:04.0 Off |                    0 |
| N/A   43C    P8             10W /   70W |       0MiB /  15360MiB |      0%      Default |
|                                         |                        |                  N/A |
+-----------------------------------------+-----

In [1]:
%cd /content

!git clone -b stage-wise-ct \
    https://github.com/Syed1611/curvature-tuning-research.git

%cd /content/curvature-tuning-research/src/curvature-tuning

!git branch --show-current
!git log -1 --oneline

/content
Cloning into 'curvature-tuning-research'...


remote: Enumerating objects: 575, done.
remote: Counting objects: 100% (247/247), done.
remote: Compressing objects: 100% (123/123), done.
remote: Total 575 (delta 153), reused 181 (delta 103), pack-reused 328 (from 1)
Receiving objects: 100% (575/575), 6.93 MiB | 5.87 MiB/s, done.
Resolving deltas: 100% (284/284), done.
/content/curvature-tuning-research/src/curvature-tuning
stage-wise-ct
068c466 (HEAD -> stage-wise-ct, origin/stage-wise-ct, origin/HEAD) Updated aircraft with complete results


## Environment Setup

The repository dependencies are installed before running the experiments.

After installation, the Colab runtime should be restarted so that the required package versions are loaded correctly.

In [2]:
%pip install -q -r requirements.txt
%pip install --force-reinstall --no-cache-dir "numpy==1.26.3"

  Preparing metadata (setup.py) ... done
     ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 15.7/15.7 MB 80.2 MB/s eta 0:00:0000:0100:01
  Installing build dependencies ... done
  Getting requirements to build wheel ... done
  Installing backend dependencies ... done
  Preparing metadata (pyproject.toml) ... done
     ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 42.4/42.4 kB 1.6 MB/s eta 0:00:00
     ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 57.6/57.6 kB 2.7 MB/s eta 0:00:00
     ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 89.9/89.9 kB 4.8 MB/s eta 0:00:00
   ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 64.9/64.9 kB 2.4 MB/s eta 0:00:00
   ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 133.2/133.2 kB 7.2 MB/s eta 0:00:00
   ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 2.3/2.3 MB 64.4 MB/s eta 0:00:00:00:01
   ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 78.4/78.4 kB 3.8 MB/s eta 0:00:00
   ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━ 12.7/12.7 MB 99.5 MB/s eta 0:00:00:00:010:01
   ━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━━

In [1]:
%cd /content/curvature-tuning-research/src/curvature-tuning

import os
import torch

os.environ["WANDB_MODE"] = "disabled"

print("Working directory:", os.getcwd())
print("PyTorch:", torch.__version__)
print("CUDA available:", torch.cuda.is_available())

if torch.cuda.is_available():
    print("GPU:", torch.cuda.get_device_name(0))

/content/curvature-tuning-research/src/curvature-tuning
Working directory: /content/curvature-tuning-research/src/curvature-tuning
PyTorch: 2.11.0+cu128
CUDA available: True
GPU: Tesla T4


## Arabic Digits Dataset

Before running the experiments, the Arabic Digits data loaders are checked to confirm that the downstream dataset can be loaded correctly.

The same dataset split and random seed protocol are used for Baseline, S-CT, and Learned SW-CT so that the methods are compared under the same conditions.

In [ ]:
from utils.data import get_data_loaders

train_loader, test_loader, val_loader = get_data_loaders(
    "imagenet_to_arabic-digits",
    train_batch_size=32,
    test_batch_size=128,
    seed=42,
)

print("Train samples:", len(train_loader.dataset))
print("Validation samples:", len(val_loader.dataset))
print("Test samples:", len(test_loader.dataset))

images, labels = next(iter(train_loader))

print("Image batch shape:", images.shape)
print("Label batch shape:", labels.shape)
print("Labels:", labels[:10])

README.md:   0%|          | 0.00/2.86k [00:00<?, ?B/s]

arabic-digits.py:   0%|          | 0.00/2.88k [00:00<?, ?B/s]

Generating train split: 0 examples [00:00, ? examples/s]

Processing train set: 100%|██████████| 60001/60001 [00:19<00:00, 3087.41it/s]


Generating test split: 0 examples [00:00, ? examples/s]

Processing test set: 100%|██████████| 10001/10001 [00:03<00:00, 3165.58it/s]


# ResNet-18 Experiments

ResNet-18 is evaluated first because it was used during the initial development of Learned SW-CT.

The experiment compares Baseline, S-CT, fixed-initialization SW-CT, and random-initialization SW-CT.

All methods use the same ImageNet-pretrained backbone, Arabic Digits dataset split, experimental seeds, and downstream training protocol.

## ResNet-18 — 20-Epoch Evaluation

The first evaluation uses 20 training epochs.

This provides the primary reference experiment and maintains compatibility with the earlier Learned SW-CT work.

### Methods

**Baseline**

The pretrained ResNet-18 retains its original ReLU activations. The backbone is frozen and only the downstream classifier is trained.

**S-CT**

The original Single-Parameter Curvature Tuning method searches over a single beta shared throughout the network. Candidate beta values from 0.70 to 1.00 are evaluated using validation performance, and the best candidate is evaluated on the test set.

The recorded S-CT execution time includes the complete beta search rather than only the final selected beta.

**Learned SW-CT — Fixed Initialization**

Four trainable beta parameters are assigned to the four ResNet stages. All four begin at beta = 0.78.

This preserves the initialization used in the original Learned SW-CT experiments.

**Learned SW-CT — Random Initialization**

Four trainable stage-wise beta parameters are initialized independently between 0.70 and 0.99.

The random initialization is generated deterministically from the experiment seed. This allows the experiment to test whether Learned SW-CT depends on the fixed 0.78 starting value while remaining reproducible.

In [ ]:
!CUDA_VISIBLE_DEVICES=1 WANDB_MODE=disabled python generalization_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds arabic-digits \
    --seed 42 \
    --linear_probe_train_bs 32 \
    --linear_probe_test_bs 128 \
    --epochs 20

2026-10-01 21:15:42.048 | INFO     | __main__:main:74 - Log file: ./logs/generalization_ct_imagenet_to_arabic-digits_resnet18_seed42_epochs20.log
2026-10-01 21:15:42.050 | INFO     | __main__:main:78 - Running on cuda
2026-10-01 21:16:54.777 | INFO     | __main__:main:105 - Testing baseline...
2026-10-01 21:16:54.793 | INFO     | __main__:main:116 - Number of trainable parameters: 5130
2026-10-01 21:16:54.793 | INFO     | __main__:main:117 - Starting transfer learning...
2026-10-01 21:18:24.336 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 2.491875, Accuracy: 9.38%
2026-10-01 21:18:24.678 | INFO     | train:train_epoch:47 - Epoch 1, Step 100, Loss: 2.352832, Accuracy: 9.78%
2026-10-01 21:18:25.045 | INFO     | train:train_epoch:47 - Epoch 1, Step 200, Loss: 2.214385, Accuracy: 22.82%
2026-10-01 21:18:25.397 | INFO     | train:train_epoch:47 - Epoch 1, Step 300, Loss: 2.050452, Accuracy: 38.55%
2026-10-01 21:18:25.754 | INFO     | train:train_epoch:47 - Epoch 1, Step 400, L

In [ ]:
!CUDA_VISIBLE_DEVICES=1 WANDB_MODE=disabled python generalization_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds arabic-digits \
    --seed 43 \
    --linear_probe_train_bs 32 \
    --linear_probe_test_bs 128 \
    --epochs 20

2026-10-01 23:47:50.761 | INFO     | __main__:main:74 - Log file: ./logs/generalization_ct_imagenet_to_arabic-digits_resnet18_seed43_epochs20.log
2026-10-01 23:47:50.763 | INFO     | __main__:main:78 - Running on cuda
2026-10-01 23:49:11.783 | INFO     | __main__:main:105 - Testing baseline...
2026-10-01 23:49:11.803 | INFO     | __main__:main:116 - Number of trainable parameters: 5130
2026-10-01 23:49:11.804 | INFO     | __main__:main:117 - Starting transfer learning...
2026-10-01 23:50:49.551 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 2.629095, Accuracy: 3.12%
2026-10-01 23:50:49.853 | INFO     | train:train_epoch:47 - Epoch 1, Step 100, Loss: 2.367169, Accuracy: 10.64%
2026-10-01 23:50:50.205 | INFO     | train:train_epoch:47 - Epoch 1, Step 200, Loss: 2.229121, Accuracy: 22.33%
2026-10-01 23:50:50.580 | INFO     | train:train_epoch:47 - Epoch 1, Step 300, Loss: 2.060868, Accuracy: 37.72%
2026-10-01 23:50:50.952 | INFO     | train:train_epoch:47 - Epoch 1, Step 400, 

In [ ]:
!CUDA_VISIBLE_DEVICES=1 WANDB_MODE=disabled python generalization_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds arabic-digits \
    --seed 44 \
    --linear_probe_train_bs 32 \
    --linear_probe_test_bs 128 \
    --epochs 20

2026-10-02 01:59:46.601 | INFO     | __main__:main:74 - Log file: ./logs/generalization_ct_imagenet_to_arabic-digits_resnet18_seed44_epochs20.log
2026-10-02 01:59:46.604 | INFO     | __main__:main:78 - Running on cuda
2026-10-02 02:01:30.844 | INFO     | __main__:main:105 - Testing baseline...
2026-10-02 02:01:30.863 | INFO     | __main__:main:116 - Number of trainable parameters: 5130
2026-10-02 02:01:30.864 | INFO     | __main__:main:117 - Starting transfer learning...
2026-10-02 02:03:10.798 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 2.509773, Accuracy: 6.25%
2026-10-02 02:03:11.137 | INFO     | train:train_epoch:47 - Epoch 1, Step 100, Loss: 2.409749, Accuracy: 12.41%
2026-10-02 02:03:11.513 | INFO     | train:train_epoch:47 - Epoch 1, Step 200, Loss: 2.255540, Accuracy: 20.21%
2026-10-02 02:03:11.853 | INFO     | train:train_epoch:47 - Epoch 1, Step 300, Loss: 2.084264, Accuracy: 34.60%
2026-10-02 02:03:12.225 | INFO     | train:train_epoch:47 - Epoch 1, Step 400, 

### Learned SW-CT with Fixed Beta Initialization

The original Learned SW-CT configuration is first reproduced using the fixed initialization:

\[[\beta_1,\beta_2,\beta_3,\beta_4]=[0.78,0.78,0.78,0.78].\]

The initial value is only a starting point. During training, the four beta parameters are optimized independently together with the downstream classifier.

These runs provide the reference against which random initialization will be compared.

In [ ]:
!CUDA_VISIBLE_DEVICES=1 WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds arabic-digits \
    --seed 42 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy fixed \
    --init_beta 0.78 \
    --beta_lr 0.01 \
    --epochs 20

2026-10-02 04:13:15.538 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_arabic-digits_resnet18_seed42_epochs20_initfixed0.78_betalr0.01.log
2026-10-02 04:13:15.610 | INFO     | __main__:main:302 - Running on cuda
2026-10-02 04:14:59.065 | INFO     | __main__:main:389 - Initialization strategy: fixed
2026-10-02 04:14:59.066 | INFO     | __main__:main:394 - Requested initial stage betas: [0.78, 0.78, 0.78, 0.78]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-02 04:14:59.108 | INFO     | __main__:main:418 - Initial stage betas: [0.7799999713897705, 0.7799999713897705, 0.7799999713897705, 0.7799999713897705]
2026-10-02 04:14:59.109 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-02 04:14:59.109 | INFO     | __main__:main:439 - Total trainable parameters: 5134
2026-10-02 04:15:00.314 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 2.645525, Accuracy: 0.00%
2026-10-02 04:15:16.054 | INFO     | train:train_epoch:

In [ ]:
!CUDA_VISIBLE_DEVICES=1 WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds arabic-digits \
    --seed 43 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy fixed \
    --init_beta 0.78 \
    --beta_lr 0.01 \
    --epochs 20

2026-10-02 05:43:13.971 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_arabic-digits_resnet18_seed43_epochs20_initfixed0.78_betalr0.01.log
2026-10-02 05:43:14.059 | INFO     | __main__:main:302 - Running on cuda
2026-10-02 05:45:05.145 | INFO     | __main__:main:389 - Initialization strategy: fixed
2026-10-02 05:45:05.145 | INFO     | __main__:main:394 - Requested initial stage betas: [0.78, 0.78, 0.78, 0.78]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-02 05:45:05.171 | INFO     | __main__:main:418 - Initial stage betas: [0.7799999713897705, 0.7799999713897705, 0.7799999713897705, 0.7799999713897705]
2026-10-02 05:45:05.171 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-02 05:45:05.172 | INFO     | __main__:main:439 - Total trainable parameters: 5134
2026-10-02 05:45:06.061 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 2.467699, Accuracy: 6.25%
2026-10-02 05:45:21.487 | INFO     | train:train_epoch:

In [ ]:
!CUDA_VISIBLE_DEVICES=1 WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds arabic-digits \
    --seed 44 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy fixed \
    --init_beta 0.78 \
    --beta_lr 0.01 \
    --epochs 20

2026-10-02 08:53:12.486 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_arabic-digits_resnet18_seed44_epochs20_initfixed0.78_betalr0.01.log
2026-10-02 08:53:12.541 | INFO     | __main__:main:302 - Running on cuda
Downloading: "https://download.pytorch.org/models/resnet18-f37072fd.pth" to /root/.cache/torch/hub/checkpoints/resnet18-f37072fd.pth
100%|███████████████████████████████████████| 44.7M/44.7M [00:00<00:00, 184MB/s]
2026-10-02 08:54:37.627 | INFO     | __main__:main:389 - Initialization strategy: fixed
2026-10-02 08:54:37.627 | INFO     | __main__:main:394 - Requested initial stage betas: [0.78, 0.78, 0.78, 0.78]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-02 08:54:37.682 | INFO     | __main__:main:418 - Initial stage betas: [0.7799999713897705, 0.7799999713897705, 0.7799999713897705, 0.7799999713897705]
2026-10-02 08:54:37.683 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-02 08:54:37.683 | INFO     | __m

### Learned SW-CT with Random Beta Initialization

The fixed beta = 0.78 initialization may raise the question of whether Learned SW-CT performs well only because its starting point was informed by the earlier S-CT experiments.

To test this dependency, each of the four stage-wise beta parameters is now initialized independently from a uniform distribution between 0.70 and 0.99.

The initialization is reproducible: the random generator is seeded using the experiment seed. Therefore, each seed always receives the same initial beta vector.

If random initialization produces similar performance to the fixed 0.78 experiment, this provides evidence that the Learned SW-CT result is not dependent on a single hand-selected initialization.

In [ ]:
!CUDA_VISIBLE_DEVICES=1 WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds arabic-digits \
    --seed 42 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy random \
    --beta_lr 0.01 \
    --epochs 20

2026-10-02 10:23:21.030 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_arabic-digits_resnet18_seed42_epochs20_initrandom_betalr0.01.log
2026-10-02 10:23:21.122 | INFO     | __main__:main:302 - Running on cuda
2026-10-02 10:24:58.071 | INFO     | __main__:main:389 - Initialization strategy: random
2026-10-02 10:24:58.072 | INFO     | __main__:main:394 - Requested initial stage betas: [0.924447, 0.827275, 0.948993, 0.902237]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-02 10:24:58.107 | INFO     | __main__:main:418 - Initial stage betas: [0.924447238445282, 0.827274739742279, 0.9489933848381042, 0.9022367000579834]
2026-10-02 10:24:58.108 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-02 10:24:58.108 | INFO     | __main__:main:439 - Total trainable parameters: 5134
2026-10-02 10:24:59.227 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 2.700262, Accuracy: 0.00%
2026-10-02 10:25:14.902 | INFO     | train:

In [ ]:
!CUDA_VISIBLE_DEVICES=1 WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds arabic-digits \
    --seed 43 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy random \
    --beta_lr 0.01 \
    --epochs 20

2026-10-02 11:53:57.148 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_arabic-digits_resnet18_seed43_epochs20_initrandom_betalr0.01.log
2026-10-02 11:53:57.226 | INFO     | __main__:main:302 - Running on cuda
2026-10-02 11:55:20.735 | INFO     | __main__:main:389 - Initialization strategy: random
2026-10-02 11:55:20.736 | INFO     | __main__:main:394 - Requested initial stage betas: [0.889167, 0.712695, 0.705809, 0.943372]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-02 11:55:20.768 | INFO     | __main__:main:418 - Initial stage betas: [0.8891667127609253, 0.7126947641372681, 0.7058085799217224, 0.9433716535568237]
2026-10-02 11:55:20.769 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-02 11:55:20.769 | INFO     | __main__:main:439 - Total trainable parameters: 5134
2026-10-02 11:55:21.778 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 2.482014, Accuracy: 9.38%
2026-10-02 11:55:38.136 | INFO     | trai

In [ ]:
!CUDA_VISIBLE_DEVICES=1 WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds arabic-digits \
    --seed 44 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy random \
    --beta_lr 0.01 \
    --epochs 20

2026-10-02 13:24:12.246 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_arabic-digits_resnet18_seed44_epochs20_initrandom_betalr0.01.log
2026-10-02 13:24:12.317 | INFO     | __main__:main:302 - Running on cuda
2026-10-02 13:25:35.237 | INFO     | __main__:main:389 - Initialization strategy: random
2026-10-02 13:25:35.237 | INFO     | __main__:main:394 - Requested initial stage betas: [0.735544, 0.774853, 0.817674, 0.981063]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-02 13:25:35.267 | INFO     | __main__:main:418 - Initial stage betas: [0.7355440258979797, 0.7748528122901917, 0.8176735043525696, 0.9810633659362793]
2026-10-02 13:25:35.268 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-02 13:25:35.268 | INFO     | __main__:main:439 - Total trainable parameters: 5134
2026-10-02 13:25:36.265 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 2.414301, Accuracy: 3.12%
2026-10-02 13:25:52.176 | INFO     | trai

# ResNet-18 — 30-Epoch Evaluation

The same experiments are now repeated for 30 epochs.

The purpose of increasing the training budget is to determine whether the 20-epoch results are limited by insufficient optimization.

If a method improves substantially with 30 epochs, this suggests that additional optimization is useful. If performance remains similar, it indicates that the method has largely stabilized within the original 20-epoch training budget.

All other experimental settings remain unchanged.

For random-initialization SW-CT, the same seed produces exactly the same initial four-beta vector in both the 20-epoch and 30-epoch experiments. Therefore, initialization is held constant while the training duration changes.

Execution time is again recorded to measure the computational cost of extending training from 20 to 30 epochs.

In [ ]:
!CUDA_VISIBLE_DEVICES=1 WANDB_MODE=disabled python generalization_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds arabic-digits \
    --seed 42 \
    --linear_probe_train_bs 32 \
    --linear_probe_test_bs 128 \
    --epochs 30

2026-10-02 14:54:44.888 | INFO     | __main__:main:74 - Log file: ./logs/generalization_ct_imagenet_to_arabic-digits_resnet18_seed42_epochs30.log
2026-10-02 14:54:44.891 | INFO     | __main__:main:78 - Running on cuda
2026-10-02 14:56:11.126 | INFO     | __main__:main:105 - Testing baseline...
2026-10-02 14:56:11.146 | INFO     | __main__:main:116 - Number of trainable parameters: 5130
2026-10-02 14:56:11.146 | INFO     | __main__:main:117 - Starting transfer learning...
2026-10-02 14:57:39.063 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 2.491875, Accuracy: 9.38%
2026-10-02 14:57:39.421 | INFO     | train:train_epoch:47 - Epoch 1, Step 100, Loss: 2.352832, Accuracy: 9.78%
2026-10-02 14:57:39.789 | INFO     | train:train_epoch:47 - Epoch 1, Step 200, Loss: 2.214385, Accuracy: 22.82%
2026-10-02 14:57:40.158 | INFO     | train:train_epoch:47 - Epoch 1, Step 300, Loss: 2.050452, Accuracy: 38.55%
2026-10-02 14:57:40.518 | INFO     | train:train_epoch:47 - Epoch 1, Step 400, L

In [ ]:
!CUDA_VISIBLE_DEVICES=1 WANDB_MODE=disabled python generalization_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds arabic-digits \
    --seed 43 \
    --linear_probe_train_bs 32 \
    --linear_probe_test_bs 128 \
    --epochs 30

2026-10-02 17:38:53.155 | INFO     | __main__:main:74 - Log file: ./logs/generalization_ct_imagenet_to_arabic-digits_resnet18_seed43_epochs30.log
2026-10-02 17:38:53.158 | INFO     | __main__:main:78 - Running on cuda
2026-10-02 17:40:21.167 | INFO     | __main__:main:105 - Testing baseline...
2026-10-02 17:40:21.186 | INFO     | __main__:main:116 - Number of trainable parameters: 5130
2026-10-02 17:40:21.187 | INFO     | __main__:main:117 - Starting transfer learning...
2026-10-02 17:41:41.896 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 2.629095, Accuracy: 3.12%
2026-10-02 17:41:42.232 | INFO     | train:train_epoch:47 - Epoch 1, Step 100, Loss: 2.367169, Accuracy: 10.64%
2026-10-02 17:41:42.584 | INFO     | train:train_epoch:47 - Epoch 1, Step 200, Loss: 2.229121, Accuracy: 22.33%
2026-10-02 17:41:42.938 | INFO     | train:train_epoch:47 - Epoch 1, Step 300, Loss: 2.060868, Accuracy: 37.72%
2026-10-02 17:41:43.289 | INFO     | train:train_epoch:47 - Epoch 1, Step 400, 

In [4]:
!CUDA_VISIBLE_DEVICES=1 WANDB_MODE=disabled python generalization_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds arabic-digits \
    --seed 44 \
    --linear_probe_train_bs 32 \
    --linear_probe_test_bs 128 \
    --epochs 30

2026-10-03 00:14:58.543 | INFO     | __main__:main:74 - Log file: ./logs/generalization_ct_imagenet_to_arabic-digits_resnet18_seed44_epochs30.log
2026-10-03 00:14:58.546 | INFO     | __main__:main:78 - Running on cuda
2026-10-03 00:16:15.502 | INFO     | __main__:main:105 - Testing baseline...
2026-10-03 00:16:15.529 | INFO     | __main__:main:116 - Number of trainable parameters: 5130
2026-10-03 00:16:15.530 | INFO     | __main__:main:117 - Starting transfer learning...
2026-10-03 00:17:50.996 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 2.509773, Accuracy: 6.25%
2026-10-03 00:17:51.281 | INFO     | train:train_epoch:47 - Epoch 1, Step 100, Loss: 2.409749, Accuracy: 12.41%
2026-10-03 00:17:51.555 | INFO     | train:train_epoch:47 - Epoch 1, Step 200, Loss: 2.255540, Accuracy: 20.21%
2026-10-03 00:17:51.871 | INFO     | train:train_epoch:47 - Epoch 1, Step 300, Loss: 2.084264, Accuracy: 34.60%
2026-10-03 00:17:52.198 | INFO     | train:train_epoch:47 - Epoch 1, Step 400, 

In [5]:
!CUDA_VISIBLE_DEVICES=1 WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds arabic-digits \
    --seed 42 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy fixed \
    --init_beta 0.78 \
    --beta_lr 0.01 \
    --epochs 30

2026-10-03 03:01:45.712 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_arabic-digits_resnet18_seed42_epochs30_initfixed0.78_betalr0.01.log
2026-10-03 03:01:45.797 | INFO     | __main__:main:302 - Running on cuda
2026-10-03 03:03:11.084 | INFO     | __main__:main:389 - Initialization strategy: fixed
2026-10-03 03:03:11.084 | INFO     | __main__:main:394 - Requested initial stage betas: [0.78, 0.78, 0.78, 0.78]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-03 03:03:11.128 | INFO     | __main__:main:418 - Initial stage betas: [0.7799999713897705, 0.7799999713897705, 0.7799999713897705, 0.7799999713897705]
2026-10-03 03:03:11.129 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-03 03:03:11.129 | INFO     | __main__:main:439 - Total trainable parameters: 5134
2026-10-03 03:03:12.332 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 2.645525, Accuracy: 0.00%
2026-10-03 03:03:28.162 | INFO     | train:train_epoch:

In [6]:
!CUDA_VISIBLE_DEVICES=1 WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds arabic-digits \
    --seed 43 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy fixed \
    --init_beta 0.78 \
    --beta_lr 0.01 \
    --epochs 30

2026-10-03 05:17:03.123 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_arabic-digits_resnet18_seed43_epochs30_initfixed0.78_betalr0.01.log
2026-10-03 05:17:03.213 | INFO     | __main__:main:302 - Running on cuda
2026-10-03 05:18:25.422 | INFO     | __main__:main:389 - Initialization strategy: fixed
2026-10-03 05:18:25.423 | INFO     | __main__:main:394 - Requested initial stage betas: [0.78, 0.78, 0.78, 0.78]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-03 05:18:25.459 | INFO     | __main__:main:418 - Initial stage betas: [0.7799999713897705, 0.7799999713897705, 0.7799999713897705, 0.7799999713897705]
2026-10-03 05:18:25.460 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-03 05:18:25.460 | INFO     | __main__:main:439 - Total trainable parameters: 5134
2026-10-03 05:18:26.462 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 2.467699, Accuracy: 6.25%
2026-10-03 05:18:42.964 | INFO     | train:train_epoch:

In [3]:
!CUDA_VISIBLE_DEVICES=1 WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds arabic-digits \
    --seed 44 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy fixed \
    --init_beta 0.78 \
    --beta_lr 0.01 \
    --epochs 30

2026-10-03 08:55:59.360 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_arabic-digits_resnet18_seed44_epochs30_initfixed0.78_betalr0.01.log
2026-10-03 08:55:59.417 | INFO     | __main__:main:302 - Running on cuda
Downloading: "https://download.pytorch.org/models/resnet18-f37072fd.pth" to /root/.cache/torch/hub/checkpoints/resnet18-f37072fd.pth
100%|███████████████████████████████████████| 44.7M/44.7M [00:00<00:00, 169MB/s]
2026-10-03 08:57:00.013 | INFO     | __main__:main:389 - Initialization strategy: fixed
2026-10-03 08:57:00.014 | INFO     | __main__:main:394 - Requested initial stage betas: [0.78, 0.78, 0.78, 0.78]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-03 08:57:00.124 | INFO     | __main__:main:418 - Initial stage betas: [0.7799999713897705, 0.7799999713897705, 0.7799999713897705, 0.7799999713897705]
2026-10-03 08:57:00.125 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-03 08:57:00.125 | INFO     | __m

In [4]:
!CUDA_VISIBLE_DEVICES=1 WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds arabic-digits \
    --seed 42 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy random \
    --beta_lr 0.01 \
    --epochs 30

2026-10-03 11:07:21.522 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_arabic-digits_resnet18_seed42_epochs30_initrandom_betalr0.01.log
2026-10-03 11:07:21.626 | INFO     | __main__:main:302 - Running on cuda
2026-10-03 11:08:50.175 | INFO     | __main__:main:389 - Initialization strategy: random
2026-10-03 11:08:50.176 | INFO     | __main__:main:394 - Requested initial stage betas: [0.924447, 0.827275, 0.948993, 0.902237]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-03 11:08:50.209 | INFO     | __main__:main:418 - Initial stage betas: [0.924447238445282, 0.827274739742279, 0.9489933848381042, 0.9022367000579834]
2026-10-03 11:08:50.210 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-03 11:08:50.210 | INFO     | __main__:main:439 - Total trainable parameters: 5134
2026-10-03 11:08:51.136 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 2.700262, Accuracy: 0.00%
2026-10-03 11:09:06.582 | INFO     | train:

In [5]:
!CUDA_VISIBLE_DEVICES=1 WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds arabic-digits \
    --seed 43 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy random \
    --beta_lr 0.01 \
    --epochs 30

2026-10-03 13:19:13.080 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_arabic-digits_resnet18_seed43_epochs30_initrandom_betalr0.01.log
2026-10-03 13:19:13.180 | INFO     | __main__:main:302 - Running on cuda
2026-10-03 13:20:49.780 | INFO     | __main__:main:389 - Initialization strategy: random
2026-10-03 13:20:49.781 | INFO     | __main__:main:394 - Requested initial stage betas: [0.889167, 0.712695, 0.705809, 0.943372]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-03 13:20:49.821 | INFO     | __main__:main:418 - Initial stage betas: [0.8891667127609253, 0.7126947641372681, 0.7058085799217224, 0.9433716535568237]
2026-10-03 13:20:49.822 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-03 13:20:49.822 | INFO     | __main__:main:439 - Total trainable parameters: 5134
2026-10-03 13:20:50.876 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 2.482014, Accuracy: 9.38%
2026-10-03 13:21:06.376 | INFO     | trai

In [3]:
!CUDA_VISIBLE_DEVICES=1 WANDB_MODE=disabled python generalization_stagewise_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds arabic-digits \
    --seed 44 \
    --transfer_train_bs 32 \
    --transfer_test_bs 128 \
    --init_strategy random \
    --beta_lr 0.01 \
    --epochs 30

2026-10-03 17:27:10.579 | INFO     | __main__:main:286 - Log file: ./logs/generalization_stagewise_ct_imagenet_to_arabic-digits_resnet18_seed44_epochs30_initrandom_betalr0.01.log
2026-10-03 17:27:10.641 | INFO     | __main__:main:302 - Running on cuda
Downloading: "https://download.pytorch.org/models/resnet18-f37072fd.pth" to /root/.cache/torch/hub/checkpoints/resnet18-f37072fd.pth
100%|███████████████████████████████████████| 44.7M/44.7M [00:00<00:00, 163MB/s]
2026-10-03 17:28:15.918 | INFO     | __main__:main:389 - Initialization strategy: random
2026-10-03 17:28:15.919 | INFO     | __main__:main:394 - Requested initial stage betas: [0.735544, 0.774853, 0.817674, 0.981063]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
2026-10-03 17:28:15.989 | INFO     | __main__:main:418 - Initial stage betas: [0.7355440258979797, 0.7748528122901917, 0.8176735043525696, 0.9810633659362793]
2026-10-03 17:28:15.989 | INFO     | __main__:main:434 - Trainable curvature parameters: 4
2026-10-03 17:28:15.989 | 